# Planet basemap parcel statistics

Choose `INPUT_MODE = "local"` to reuse downloaded tiles, or `"catalog"` to
fetch imagery from the HUB. Both modes use the same cleaning and statistics.
Local source tiles are always preserved.


In [1]:
import os
from pathlib import Path

from common_libraries.io_library import read_data
from common_libraries.catalog_library import CatalogSearchUtils
from parcel_stats_pipeline import PlanetBasemapZonalStats
from hub_catalog.planet_delivery import build_local_planet_manifest

# Reuse the adapter's densified raster-footprint calculation for coverage selection.
from hub_catalog.planet_parcel_stats import _raster_footprints


c:\ProgramData\anaconda3\envs\axhub_spatial\Lib\site-packages\xicor\__init__.py:1: UserWarning: pkg_resources is deprecated as an API. See https://setuptools.pypa.io/en/latest/pkg_resources.html. The pkg_resources package is slated for removal as early as 2025-11-30. Refrain from using this package or pin to Setuptools<81.
  from pkg_resources import get_distribution, DistributionNotFound


In [2]:
WORK_PATH = Path("C:/work_dir")
RUN_IDENTIFIER = "volvi-2023-2024"
PARCELS_PATH = WORK_PATH / RUN_IDENTIFIER / "parcels_volvi.gpkg"
BSM_TILES_PATH = WORK_PATH / "planet_basemap_quads.gpkg"
INPUT_MODE = "local"  # "local" reuses files; "catalog" downloads from HUB.
LOCAL_TILES_PATH = WORK_PATH / "planet_local_2025_01_09"
# Catalog-mode scratch only. It is not searched for existing source tiles.
DELETE_TEMPORARY_FILES = False  # True removes only scratch files owned by this run.
SCRATCH_PATH = WORK_PATH / RUN_IDENTIFIER / "planet_scratch"
OUTPUT_DIR = WORK_PATH / RUN_IDENTIFIER / "1_planet_parcel_stats"
START_DATE = "2025-01-01"
END_DATE = "2025-09-30"
WORKING_EPSG = 2100
PARCEL_ID_FIELD = "parcel_code"
QUAD_ID_FIELD = "quad_id"
COLLECTION_ID = "PL_BSM"
ANALYSIS_PATTERN = "*quad_bandmath*.tif"  # Adjust only if catalog filenames differ.

# NDMI requires SWIR, which Planet eight-band tiles do not contain.
PLANET_INDICES = ["EVI", "NDRE", "NDVI", "NDWI", "SAVI"]
SPATIAL_STATISTICS = ["mean", "median", "sd", "min", "max", "range"]
REFLECTANCE_SCALE = 0.0001  # Fallback for DN scaled by 10000; use 1.0 for reflectance already in 0-1 units.


## Parcels and intersecting quads
CRS metadata is required. The extractor repairs polygon geometries while preserving
multipart parcels, identifiers and source attributes. Do not explode multipart
parcels into duplicate IDs. Copy any label enrichment from your original notebook
here if those labels are not already stored in the parcel file.


In [3]:
gdf_parcels = read_data(str(PARCELS_PATH))
gdf_tiles = read_data(str(BSM_TILES_PATH))
if gdf_parcels.crs is None or gdf_tiles.crs is None:
    raise ValueError("Parcels and tile grid must have explicit CRS metadata")
gdf_tiles = gdf_tiles.to_crs(WORKING_EPSG)
if INPUT_MODE not in {"local", "catalog"}:
    raise ValueError('INPUT_MODE must be "local" or "catalog"')
if INPUT_MODE == "local":
    local_manifest = build_local_planet_manifest(
        LOCAL_TILES_PATH, start_date=START_DATE, end_date=END_DATE,
    )
    # A local tile selection may cover only part of the parcel dataset.
    # Select covered parcels explicitly and save excluded ones for inspection.
    gdf_tiles = gdf_tiles[gdf_tiles[QUAD_ID_FIELD].astype(str).isin(local_manifest.quad_id)].copy()
    footprints = _raster_footprints(local_manifest, WORKING_EPSG)
    metric_parcels = gdf_parcels.to_crs(WORKING_EPSG)
    covered = metric_parcels.geometry.notna()
    # A parcel needs complete coverage in every requested month, not just one.
    for _, month_tiles in footprints.groupby("period_start"):
        coverage = month_tiles.geometry.union_all().buffer(1e-6)
        covered &= metric_parcels.geometry.covered_by(coverage)
    OUTPUT_DIR.mkdir(parents=True, exist_ok=True)
    if (~covered).any():
        gdf_parcels.loc[~covered].to_parquet(OUTPUT_DIR / "outside_local_tiles.geoparquet", index=False)
    print(f"Local coverage: {covered.sum()} parcels; {(~covered).sum()} excluded")
    gdf_parcels = gdf_parcels.loc[covered].copy()
    # The extractor also checks actual raster footprints for every month.

extractor = PlanetBasemapZonalStats(
    parcels=gdf_parcels, start_date=START_DATE, end_date=END_DATE,
    output_dir=OUTPUT_DIR, working_epsg=WORKING_EPSG,
    parcel_id_field=PARCEL_ID_FIELD,
    resolution_metres=5, batch_size_metres=2000, buffer_metres=100,
    max_cube_bytes=512_000_000,
    indices=PLANET_INDICES, reflectance_scale=REFLECTANCE_SCALE,
    spatial_statistics=SPATIAL_STATISTICS,
    remove_outliers=True, iqr_quantiles=(0.1, 0.9), iqr_multiplier=1.5,
    iqr_min_valid_pixels=20, fill_nulls=True,
    temporal_fill_mode="bidirectional",  # Matches 1_parcel_stats; use past_only for causal features.
    minimum_parcel_pixels=3, minimum_observed_fraction_for_fill=0.20,
    spatial_fill_window_sizes=(3, 5), interpolation_method="nearest",
    interpolation_max_distance_in_meters=500,
)
# Select tiles intersecting the parcels; run_catalog assigns each parcel once.
study_area = extractor.parcels.to_crs(WORKING_EPSG).geometry.union_all()
gdf_tiles = gdf_tiles[gdf_tiles.intersects(study_area)].copy()
if gdf_tiles.empty:
    raise ValueError("No Planet quads intersect the study area")
print(f"{len(extractor.parcels)} parcels; {len(gdf_tiles)} quads")
gdf_tiles

Reading file: C:/work_dir/volvi-2023-2024/parcels_volvi.gpkg
Reading file: C:/work_dir/planet_basemap_quads.gpkg
Local coverage: 28699 parcels; 0 excluded


2026-09-06 14:30:13,352 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.orchestrator | Prepared 28699 valid parcels.
2026-09-06 14:30:13,354 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.orchestrator | Log files: orchestration=C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_zonal_stats.log, openEO=C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_openeo.log, raster filling=C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_raster_filling.log, parcel statistics=C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_parcel_statistics.log.
2026-09-06 14:30:13,355 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.orchestrator | Configured optical bands=['B1', 'B2', 'B3', 'B4', 'B5', 'B6', 'B7', 'B8'], optical indices=['EVI', 'NDRE', 'NDVI', 'NDWI', 'SAVI'], Sentinel-1 bands=[], Sentinel-1 indices=[], Sentinel-1 orbit direction=BOTH, parcel statistics=['mean', 'median', 'sd', 'min', 'max', 'range'], remove_o

28699 parcels; 9 quads


,quad_id,order,geometry
142,1154-1279,1,POLYGON ((403040...
143,1155-1279,1,POLYGON ((417858...
175,1154-1278,1,POLYGON ((402847...
176,1155-1278,1,POLYGON ((417694...
177,1156-1278,1,POLYGON ((432542...
208,1154-1277,1,POLYGON ((402653...
209,1155-1277,1,POLYGON ((417531...
210,1156-1277,1,POLYGON ((432408...
211,1157-1277,1,POLYGON ((447285...


## Connect to the catalog (catalog mode only)
Local mode needs no catalog connection or credentials.

In [4]:
if INPUT_MODE == "catalog":
    catalog = CatalogSearchUtils(
        catalog_endpoint=os.environ["CATALOG_URL"],
        client_id=os.getenv("CATALOG_CLIENT_ID", "internal"), verbose=True,
    )


## Calculate parcel statistics
Tiles are aligned to a common 5 m grid. The first eight TIFF bands follow Planet
order: coastal blue, blue, green I, green, yellow, red, red edge, NIR.
TIFF nodata and masks are respected. TIFF scale/offset metadata takes precedence;
otherwise REFLECTANCE_SCALE converts stored values to reflectance before cleaning.
Use 0.0001 for DN scaled by 10000, or 1.0 for tiles already in reflectance units.
Physical-band statistics are consequently in reflectance units.

Indices are calculated per pixel after cleaning, then each requested statistic
is calculated over parcel pixels:
- EVI = 2.5 * (B8 - B6) / (B8 + 6 * B6 - 7.5 * B2 + 1)
- NDRE = (B8 - B7) / (B8 + B7)
- NDVI = (B8 - B6) / (B8 + B6), replacing the TIFF ninth band
- NDWI = (B4 - B8) / (B4 + B8), matching the existing green/NIR definition
- SAVI = 1.5 * (B8 - B6) / (B8 + B6 + 0.5)

Zero denominators become null. NDMI = (NIR - SWIR) / (NIR + SWIR) cannot
be calculated from these tiles because they lack SWIR. Requesting it raises an
explicit error rather than substituting another band.

[Planet band order and reflectance scaling](https://support.planet.com/hc/en-us/articles/115013886368-How-is-the-Surface-Reflectance-Product-Provided)

IQR cleaning and filling use each buffered processing batch. Batch size, resolution
and buffer affect results. Cleaning needs several times the raw cube RAM; reduce
batch size if necessary. Downstream feature selection must use Planet band names.

### Input paths and retention

`LOCAL_TILES_PATH` is the existing raster directory used in local mode. It is
never deleted. `SCRATCH_PATH` is only used for new catalog downloads and
intermediate cubes; it does not discover or reuse your local tiles.

In catalog mode, `DELETE_TEMPORARY_FILES = False` retains those scratch files,
including after errors. Set it to `True` to remove only the unique directories
created by the extraction. The scratch root itself and pre-existing files remain.
Keeping scratch files can use considerable disk space and does not automatically
make them a reusable download cache. Local mode retains its intermediate cubes
in `OUTPUT_DIR`; the catalog scratch flag has no effect on local mode.

Catalog mode processes buffered tile groups and months sequentially. Neighboring
quads intersecting a batch buffer also supply pixels. Completed batch tables can
be reused with `resume=True`.


In [5]:
if INPUT_MODE == "local":
    merged_gdf = extractor.run(local_manifest)
else:
    merged_gdf = extractor.run_catalog(
        catalog, gdf_tiles, scratch_dir=SCRATCH_PATH,
        collection_id=COLLECTION_ID, quad_id_field=QUAD_ID_FIELD,
        analysis_pattern=ANALYSIS_PATTERN,
        resume=True,
        delete_temporary_files=DELETE_TEMPORARY_FILES,
    )
geoparquet_path = OUTPUT_DIR / extractor.PARCEL_OUTPUT_FILE_NAME
print(f"Saved {len(merged_gdf)} parcels and {len(merged_gdf.columns)} columns: {geoparquet_path}")
merged_gdf.head()


2026-09-06 14:30:40,346 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.orchestrator | Processing Planet batch 1 (2 parcels)
2026-09-06 14:30:40,745 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Reading monthly pixel cube C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\a234053ad6eeb55b7fe8\batch_1.nc.
2026-09-06 14:30:40,826 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.filling | Starting temporal fill (bidirectional) for batch 1, variable B1, period 2025-01-01: 488 null pixels.
2026-09-06 14:30:40,827 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.filling | Starting temporal fill (bidirectional) for batch 1, variable B1, period 2025-02-01: 313 null pixels.
2026-09-06 14:30:40,828 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.filling | Starting temporal fill (bidirectional) for batch 1, variable B1, period 2025-03-01: 342 null pixels.
2026-09-06 14:30:40,829 | INFO | openeo_

Writing file: C:/work_dir/volvi-2023-2024/1_planet_parcel_stats/monthly_cubes/a234053ad6eeb55b7fe8/batch_1_cleaning_report.partial.parquet


2026-09-06 14:30:41,068 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Saved completed cleaning checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\a234053ad6eeb55b7fe8\batch_1_cleaned.nc.
2026-09-06 14:30:41,127 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Saved completed post-index checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\a234053ad6eeb55b7fe8\batch_1_final.nc.
2026-09-06 14:30:41,128 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Removed intermediate cleaning raster C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\a234053ad6eeb55b7fe8\batch_1_cleaned.nc; raw data and audit remain available.
2026-09-06 14:30:41,141 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Calculated ['mean', 'median', 'sd', 'min', 'max', 'range'] locally for 2 parcels from batch_1.nc.
2026-09-06 14:30:41,145 | INFO | openeo_parcel_st

Writing file: C:/work_dir/volvi-2023-2024/1_planet_parcel_stats/monthly_cubes/efc5bd23b26ef1599884/batch_2_cleaning_report.partial.parquet


2026-09-06 14:30:41,771 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Saved completed cleaning checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\efc5bd23b26ef1599884\batch_2_cleaned.nc.
2026-09-06 14:30:41,824 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Saved completed post-index checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\efc5bd23b26ef1599884\batch_2_final.nc.
2026-09-06 14:30:41,826 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Removed intermediate cleaning raster C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\efc5bd23b26ef1599884\batch_2_cleaned.nc; raw data and audit remain available.
2026-09-06 14:30:41,858 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Calculated ['mean', 'median', 'sd', 'min', 'max', 'range'] locally for 10 parcels from batch_2.nc.
2026-09-06 14:30:41,861 | INFO | openeo_parcel_s

...

2026-09-06 14:42:05,995 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Saved completed cleaning checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\4c0ab8b260e83fe6e125\batch_184_cleaned.nc.
2026-09-06 14:42:06,386 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Saved completed post-index checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\4c0ab8b260e83fe6e125\batch_184_final.nc.
2026-09-06 14:42:06,391 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Removed intermediate cleaning raster C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\4c0ab8b260e83fe6e125\batch_184_cleaned.nc; raw data and audit remain available.
2026-09-06 14:42:06,567 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Calculated ['mean', 'median', 'sd', 'min', 'max', 'range'] locally for 48 parcels from batch_184.nc.
2026-09-06 14:42:06,574 | INFO | openeo_

Writing file: C:/work_dir/volvi-2023-2024/1_planet_parcel_stats/monthly_cubes/6021df28b968de59e171/batch_185_cleaning_report.partial.parquet


2026-09-06 14:42:07,214 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Saved completed cleaning checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\6021df28b968de59e171\batch_185_cleaned.nc.
2026-09-06 14:42:07,393 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Saved completed post-index checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\6021df28b968de59e171\batch_185_final.nc.
2026-09-06 14:42:07,396 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Removed intermediate cleaning raster C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\6021df28b968de59e171\batch_185_cleaned.nc; raw data and audit remain available.
2026-09-06 14:42:07,437 | INFO | openeo_parcel_stats_pipeline.zonal_stats.2036986870288.parcels | Calculated ['mean', 'median', 'sd', 'min', 'max', 'range'] locally for 12 parcels from batch_185.nc.
2026-09-06 14:42:11,161 | INFO | openeo_

Saved 28699 parcels and 961 columns: C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_parcel_time_stats.geoparquet


,parcel_code,initial_label_code,initial_label,predicted_label_code,predicted_label,prediction_probability,set_type,geometry,batch_number,intersected_pixel_count,meets_minimum_pixel_count,expected_pixel_count,temporal_filled_pixel_count,spatial_filled_pixel_count,temporal_filled_ratio,spatial_filled_ratio,data_reliability_score,pixel_area,geom_area,geom_interior_area_ratio,geom_compactness,geom_perimeter_area_ratio,geom_shape_index,geom_elongation,geom_shape_complexity_score,B1_coefficient_of_variation__20250101,B1_coefficient_of_variation__20250201,B1_coefficient_of_variation__20250301,B1_coefficient_of_variation__20250401,B1_coefficient_of_variation__20250501,B1_coefficient_of_variation__20250601,B1_coefficient_of_variation__20250701,B1_coefficient_of_variation__20250801,B1_coefficient_of_variation__20250901,B1_max__20250101,B1_max__20250201,B1_max__20250301,B1_max__20250401,B1_max__20250501,B1_max__20250601,B1_max__20250701,B1_max__20250801,B1_max__20250901,B1_mean__20250101,B1_mean__20250201,B1_mean__20250301,B1_mean__20250401,B1_mean__20250501,B1_mean__20250601,B1_mean__20250701,B1_mean__20250801,B1_mean__20250901,B1_median__20250101,B1_median__20250201,B1_median__20250301,B1_median__20250401,B1_median__20250501,B1_median__20250601,B1_median__20250701,B1_median__20250801,B1_median__20250901,B1_min__20250101,B1_min__20250201,B1_min__20250301,B1_min__20250401,B1_min__20250501,B1_min__20250601,B1_min__20250701,B1_min__20250801,B1_min__20250901,B1_range__20250101,B1_range__20250201,B1_range__20250301,B1_range__20250401,B1_range__20250501,B1_range__20250601,B1_range__20250701,B1_range__20250801,B1_range__20250901,B1_sd__20250101,B1_sd__20250201,B1_sd__20250301,B1_sd__20250401,B1_sd__20250501,B1_sd__20250601,B1_sd__20250701,B1_sd__20250801,B1_sd__20250901,B1_variance__20250101,B1_variance__20250201,B1_variance__20250301,B1_variance__20250401,B1_variance__20250501,B1_variance__20250601,B1_variance__20250701,B1_variance__20250801,B1_variance__20250901,B2_coefficient_of_variation__20250101,B2_coefficient_of_variation__20250201,B2_coefficient_of_variation__20250301,B2_coefficient_of_variation__20250401,B2_coefficient_of_variation__20250501,B2_coefficient_of_variation__20250601,B2_coefficient_of_variation__20250701,B2_coefficient_of_variation__20250801,B2_coefficient_of_variation__20250901,B2_max__20250101,B2_max__20250201,B2_max__20250301,B2_max__20250401,B2_max__20250501,B2_max__20250601,B2_max__20250701,B2_max__20250801,B2_max__20250901,B2_mean__20250101,B2_mean__20250201,B2_mean__20250301,B2_mean__20250401,B2_mean__20250501,B2_mean__20250601,B2_mean__20250701,B2_mean__20250801,B2_mean__20250901,B2_median__20250101,B2_median__20250201,B2_median__20250301,B2_median__20250401,B2_median__20250501,B2_median__20250601,B2_median__20250701,B2_median__20250801,B2_median__20250901,B2_min__20250101,B2_min__20250201,B2_min__20250301,B2_min__20250401,B2_min__20250501,B2_min__20250601,B2_min__20250701,B2_min__20250801,B2_min__20250901,B2_range__20250101,B2_range__20250201,B2_range__20250301,B2_range__20250401,B2_range__20250501,B2_range__20250601,B2_range__20250701,B2_range__20250801,B2_range__20250901,B2_sd__20250101,B2_sd__20250201,B2_sd__20250301,B2_sd__20250401,B2_sd__20250501,B2_sd__20250601,B2_sd__20250701,B2_sd__20250801,B2_sd__20250901,B2_variance__20250101,B2_variance__20250201,B2_variance__20250301,B2_variance__20250401,B2_variance__20250501,B2_variance__20250601,B2_variance__20250701,B2_variance__20250801,B2_variance__20250901,B3_coefficient_of_variation__20250101,B3_coefficient_of_variation__20250201,B3_coefficient_of_variation__20250301,B3_coefficient_of_variation__20250401,B3_coefficient_of_variation__20250501,B3_coefficient_of_variation__20250601,B3_coefficient_of_variation__20250701,B3_coefficient_of_variation__20250801,B3_coefficient_of_variation__20250901,B3_max__20250101,B3_max__20250201,B3_max__20250301,B3_max__20250401,B3_max__20250501,B3_max__20250601,B3_max__20250701,B3_max__20250801,B3_max__20250901,B3_mean__20250101,B3

## Outputs

- `satellite_parcel_time_stats.geoparquet`: parcel attributes, quality metrics and dated statistics.
- `satellite_parcel_annual_stats.geoparquet`: annual median features.
- `satellite_pixel_cleaning_report.csv`: cleaning audit.
- `planet_tile_manifest.csv`: source paths and, in catalog mode, their deletion status.
- `outside_local_tiles.geoparquet`: parcels excluded from local processing, when present.

Local source files are preserved. Catalog scratch retention follows
`DELETE_TEMPORARY_FILES`; result tables are always retained in `OUTPUT_DIR`.
